This is a seq2seq model, which uses Keras's Sequential Model.

The model contains two Bidirectional LSTM layers, an Embedding layer, and dropout.

This notebook is work in progress.

In [ ]:
import os, collections
import datetime
from datetime import date
import pandas as pd
import numpy as np
import re

from sklearn.utils import shuffle
from sklearn.model_selection import train_test_split

from tensorflow.keras.preprocessing.sequence import pad_sequences

from tensorflow.keras.models import Model, Sequential
from tensorflow.keras.layers import Input, LSTM, Dense, Embedding, Bidirectional, RepeatVector, Dropout, TimeDistributed
from tensorflow.keras.callbacks import EarlyStopping
from tensorflow.keras.optimizers import Adam

from tensorflow.keras.losses import sparse_categorical_crossentropy

In [ ]:
import tensorflow
print(tensorflow.__version__)

2.5.0


In [ ]:
# Load the TensorBoard notebook extension
%load_ext tensorboard

In [ ]:
from google.colab import drive

drive.mount('/content/gdrive')
root_path = 'gdrive/My Drive/your_project_folder/' 

Mounted at /content/gdrive


In [ ]:
def read_data_from_file(filename, data_dict):

    with open(filename) as fp:
        line = fp.readline()
        while line:
            bo, ch, ve, text = tuple(line.strip().split('\t'))
            words = text.split()
            for w in words:  
                # in the output data, composite placenames have a '_', which cannot be found in the input data
                words_split = w.split('_')               
                for word_split in words_split:
                    data_dict[bo].append(word_split)
        
            line = fp.readline()
            
    return data_dict

In [ ]:
input_file = '/content/gdrive/My Drive/data/t-in_voc'
#input_file = 't-in_voc'
input_data = collections.defaultdict(list)

output_file = '/content/gdrive/My Drive/data/t-out'
#output_file = 't-out'
output_data = collections.defaultdict(list)

input_data = read_data_from_file(input_file, input_data)
output_data = read_data_from_file(output_file, output_data)

In [ ]:
print(len(input_data['Gen']))
print(len(output_data['Gen']))

20611
20611


In [ ]:
# The reduction consists of removing the left-most marker from all
# the doubly marked prefixes and the redundant colon of the vowel
# pattern mark.

prefixes = ['!', ']', '@']

def mc_reduce(s):
   for c in prefixes:
      s = re.sub(f'{c}([^{c}]*{c})', r'\1', s)
   return s.replace(':', '')

In [ ]:
def make_in_sequences(data_dict, sequence_length):
    
    all_sequences = []
    for words_list in data_dict.values():

        for w in range(len(words_list) - sequence_length + 1):
    
            seq = ' '.join([words_list[ind] for ind in list(range(w, w + sequence_length))])
        
            all_sequences.append(seq)
        
    return all_sequences

In [ ]:
def make_out_sequences(data_dict, sequence_length):
    
    all_sequences = []
    for words_list in data_dict.values():

        for w in range(len(words_list) - sequence_length + 1):
    
            seq = ' '.join([words_list[ind] for ind in list(range(w, w + sequence_length))])
        
            seq = mc_reduce(seq)
            all_sequences.append(seq)
        
    return all_sequences

In [ ]:
sequence_length = 1

all_in_seqs = make_in_sequences(input_data, sequence_length)
all_out_seqs = make_out_sequences(output_data, sequence_length)


In [ ]:
def prepare_train_data(input_data, output_data):

    input_seqs = []
    output_seqs = []
    input_chars = set()
    output_chars = set()

    # iterate over all the books
    for seq in range(len(input_data)): 
      
        #if len(output_data[seq]) > 40:
        #  continue
          
        if "*" in input_data[seq]: # cases of ketiv/qere are complicated, just skip them!
          continue

        input_list = list(input_data[seq])

        output_list = list(output_data[seq])
        #output_list = ['\t'] + output_list + ['\n']

        input_seqs.append(input_list)
        output_seqs.append(output_list)

        for input_ch in input_list:
            input_chars.add(input_ch)
        
        for output_ch in output_list:
            output_chars.add(output_ch)
                
    
    input_chars = sorted(list(input_chars))
    output_chars = sorted(list(output_chars))
    
    max_len_input = max([len(seq) for seq in input_seqs])
    max_len_output = max([len(seq) for seq in output_seqs])
    
    # shuffle the data. The model will get the data in small batches, it is preferable if the batches are more or less homogeneous
    # of course the inputs and outputs have to be shuffled identically
    # input_seqs, output_seqs = shuffle(input_seqs, output_seqs)
    
    return input_seqs, output_seqs, input_chars, output_chars, max_len_input, max_len_output

In [ ]:
def create_dicts(input_voc, output_voc):
    
    # these dicts map the input sequences
    input_idx2char = {}
    input_char2idx = {}
    
    input_idx2char[0] = 'PAD'
    input_char2idx['PAD'] = 0

    for k, v in enumerate(input_voc):
        input_idx2char[k + 1] = v
        input_char2idx[v] = k + 1
     
    # and these dicts map the output sequences of parts of speech~
    output_idx2char = {}
    output_char2idx = {}
    
    output_idx2char[0] = 'PAD'
    output_char2idx['PAD'] = 0
    
    for k, v in enumerate(output_voc):
        output_idx2char[k + 1] = v
        output_char2idx[v] = k + 1
        
    return input_idx2char, input_char2idx, output_idx2char, output_char2idx

In [ ]:
def pad(x, length=None):

    padded_sequences = pad_sequences(x, length, padding='post')
    
    return padded_sequences

In [ ]:
def model_bidirectional(input_shape, output_sequence_length, input_vocab_size, output_vocab_size):

    model = Sequential()
    model.add(Embedding(input_vocab_size + 1, 11, input_shape=input_shape[1:]))
    
    model.add(Bidirectional(LSTM(512, 
                                 dropout=0.3,
                                 recurrent_dropout=0.2,
                                 return_sequences=False)))

    model.add(RepeatVector(output_sequence_length))

    model.add(Bidirectional(LSTM(256, 
                                 dropout = 0.3,
                                 #recurrent_dropout=0.2,
                                 return_sequences=True)))
    
    model.add(TimeDistributed(Dense(output_vocab_size + 1, activation='softmax')))
    
    adam = Adam(learning_rate=0.0005, beta_1=0.996, beta_2=0.999, epsilon=0.00000001)
    model.compile(optimizer=adam, loss=sparse_categorical_crossentropy, metrics=['accuracy'])

    return model

In [ ]:
input_seqs, output_seqs, input_chars, output_chars, max_len_input, max_len_output = prepare_train_data(all_in_seqs, all_out_seqs)
print(len(input_seqs))

299488


In [ ]:
input_idx2char, input_char2idx, output_idx2char, output_char2idx = create_dicts(input_chars, output_chars)

In [ ]:
input_seqs_num = []
output_seqs_num = []

for seq in input_seqs:
    input_seqs_num.append([input_char2idx[char] for char in seq])
    
for seq in output_seqs:
    output_seqs_num.append([output_char2idx[char] for char in seq])

In [ ]:
input_seqs_num = pad(input_seqs_num)
output_seqs_num = pad(output_seqs_num)

# sparse_categorical_crossentropy function requires the labels to be in 3 dims
output_seqs_num = output_seqs_num.reshape(*output_seqs_num.shape, 1)

In [ ]:
max_len_input = max([len(seq) for seq in input_seqs_num])
max_len_output = max([len(seq) for seq in output_seqs_num])
max_len_output

24

In [ ]:
prepared_train_x = pad(input_seqs_num, max_len_output)

In [ ]:
X_train, X_test, y_train, y_test = train_test_split(prepared_train_x, output_seqs_num, test_size=0.1, random_state=42)


In [ ]:
import tensorflow as tf

In [ ]:
rnn_model = model_bidirectional(
    X_train.shape,
    max_len_output,
    len(input_chars),
    len(output_chars))

logdir = os.path.join("logs", 'cells_512_256')
tensorboard_callback = tf.keras.callbacks.TensorBoard(logdir, histogram_freq=1)
    
rnn_model.summary()

Model: "sequential"
_________________________________________________________________
Layer (type)                 Output Shape              Param #   
embedding (Embedding)        (None, 24, 11)            363       
_________________________________________________________________
bidirectional (Bidirectional (None, 1024)              2146304   
_________________________________________________________________
repeat_vector (RepeatVector) (None, 24, 1024)          0         
_________________________________________________________________
bidirectional_1 (Bidirection (None, 24, 512)           2623488   
_________________________________________________________________
time_distributed (TimeDistri (None, 24, 41)            21033     
Total params: 4,791,188
Trainable params: 4,791,188
Non-trainable params: 0
_________________________________________________________________


In [ ]:
callback = EarlyStopping(monitor='val_loss', patience=4, verbose=0, mode='auto')
rnn_model.fit(X_train, y_train, batch_size=256, epochs=100, validation_split=0.1, callbacks=[callback, tensorboard_callback])

Epoch 1/100
948/948 [==============================] - 233s 233ms/step - loss: 1.0117 - accuracy: 0.7478 - val_loss: 0.8989 - val_accuracy: 0.7611
Epoch 2/100
948/948 [==============================] - 218s 229ms/step - loss: 0.8603 - accuracy: 0.7748 - val_loss: 0.7626 - val_accuracy: 0.8038
Epoch 3/100
948/948 [==============================] - 218s 230ms/step - loss: 0.7042 - accuracy: 0.8133 - val_loss: 0.5869 - val_accuracy: 0.8404
Epoch 4/100
948/948 [==============================] - 224s 236ms/step - loss: 0.5460 - accuracy: 0.8492 - val_loss: 0.4433 - val_accuracy: 0.8766
Epoch 5/100
948/948 [==============================] - 215s 227ms/step - loss: 0.4269 - accuracy: 0.8776 - val_loss: 0.3372 - val_accuracy: 0.9023
Epoch 6/100
948/948 [==============================] - 214s 226ms/step - loss: 0.3390 - accuracy: 0.9001 - val_loss: 0.2696 - val_accuracy: 0.9211
Epoch 7/100
948/948 [==============================] - 212s 224ms/step - loss: 0.2798 - accuracy: 0.9164 - val_loss: 0

In [ ]:
%tensorboard --logdir logs

<IPython.core.display.Javascript object>

In [ ]:
[input_idx2char[num] for num in X_test[0] if num != 0]

['W', ':', 'G', 'A', 'M']

In [ ]:

# This function undoes the reduction. The hyphen in the search pattern
# makes sure that we stay within a single analytical word.
def mc_expand(s):
   s = re.sub(r'([a-z]+)', r':\1', s)
   r = re.sub('(.)', r'\\\1', ''.join(prefixes))
   for c in prefixes:
      s = re.sub(f'([^-{r}]*{c})', f'{c}\\1', s)
   return s

In [ ]:
today = str(date.today())
filename_results = f'/content/gdrive/My Drive/data/results_morphology_{today}.txt'

correct = 0

preds = rnn_model.predict(X_test)

with open(filename_results, 'w') as f:
    for i in range(len(preds)):
        input = [input_idx2char[num] for num in X_test[i] if num != 0]
  
        pred_output = [output_idx2char[np.argmax(pred)] for pred in preds[i] if output_idx2char[np.argmax(pred)] != 'PAD']
    
        true_output = [output_idx2char[char[0]] for char in y_test[i]  if output_idx2char[char[0]] != 'PAD']

        if pred_output == true_output:
            correct += 1
            f.write(f'{"".join(input)} {mc_expand("".join(true_output))} {mc_expand("".join(pred_output))} correct \n')
        else:
            f.write(f'{"".join(input)} {mc_expand("".join(true_output))} {mc_expand("".join(pred_output))} wrong \n')

        print('input: ', ''.join(input))
        print('predicted: ', mc_expand(''.join(pred_output)))
        print('true: ', mc_expand(''.join(true_output)))
        print(' ')

accuracy = correct / len(preds)

print(accuracy)

Streaminguitvoer ingekort tot de laatste 5000 regels.
predicted:  DBR=/
true:  DBR=/
 
input:  D.:B@ROW
predicted:  DBR/+W
true:  DBR/+W
 
input:  F@V@N
predicted:  FVN/
true:  FVN/
 
input:  <AL
predicted:  <L
true:  <L
 
input:  B.:N;J
predicted:  BN/J
true:  BN/J
 
input:  HAQ.;JP
predicted:  H-QJP/
true:  !!]H](NQ&JP[/:a
 
input:  K.@L
predicted:  KL/
true:  KL/
 
input:  H@<IJR
predicted:  H-<JR/
true:  H-<JR/
 
input:  >EL
predicted:  >L
true:  >L
 
input:  >EL
predicted:  >L
true:  >L
 
input:  JIF:R@>;L
predicted:  JFR>L/
true:  JFR>L/
 
input:  P.:N;J
predicted:  PN(H/J
true:  PN(H/J
 
input:  M;>OWT
predicted:  M>(H/WT:a
true:  M>(H/WT:a
 
input:  HAC.A<AR
predicted:  H-C<R/
true:  H-C<R/
 
input:  WAJ:CAS.;P
predicted:  W:n-!J!CPP[:d
true:  W:n-!J!CSP[:d
 
input:  >ET
predicted:  >T
true:  >T
 
input:  T@MIJD
predicted:  TMJD/
true:  TMJD/
 
input:  MIP:L@V
predicted:  MPLV/
true:  MPLV/
 
input:  J:HW@H
predicted:  JHWH/
true:  JHWH/
 
input:  J:HWIH
predicted:  JHWH/
true: